In [ ]:
import torch
import torch.nn as nn
import torch.nn.functional as F
import math


# ── Shared: Multi-Head Attention ────────────────────────────────────────────

class MultiHeadAttention(nn.Module):
    """
    General multi-head attention.
    For self-attention:   pass x as both source and context.
    For cross-attention:  pass encoder output as context.
    """

    def __init__(self, d_model: int, n_heads: int, dropout: float = 0.1):
        super().__init__()
        assert d_model % n_heads == 0
        self.n_heads = n_heads
        self.d_k = d_model // n_heads

        self.q_proj   = nn.Linear(d_model, d_model, bias=False)
        self.k_proj   = nn.Linear(d_model, d_model, bias=False)
        self.v_proj   = nn.Linear(d_model, d_model, bias=False)
        self.out_proj = nn.Linear(d_model, d_model, bias=False)
        self.dropout  = nn.Dropout(dropout)

    def forward(
        self,
        query: torch.Tensor,              # (B, T_q, D)
        context: torch.Tensor,            # (B, T_kv, D)  — same as query for self-attn
        mask: torch.Tensor | None = None, # (B, 1, T_q, T_kv) bool, True = ignore
    ) -> torch.Tensor:
        B, T_q, _ = query.shape
        T_kv = context.size(1)

        def split(t, T):
            return t.view(B, T, self.n_heads, self.d_k).transpose(1, 2)

        Q = split(self.q_proj(query),   T_q)
        K = split(self.k_proj(context), T_kv)
        V = split(self.v_proj(context), T_kv)

        scores = torch.matmul(Q, K.transpose(-2, -1)) / math.sqrt(self.d_k)
        if mask is not None:
            scores = scores.masked_fill(mask, float("-inf"))

        attn = self.dropout(F.softmax(scores, dim=-1))
        out  = torch.matmul(attn, V)                              # (B, H, T_q, d_k)
        out  = out.transpose(1, 2).contiguous().view(B, T_q, -1)
        return self.out_proj(out)


class FeedForward(nn.Module):
    def __init__(self, d_model: int, d_ff: int, dropout: float = 0.1):
        super().__init__()
        self.net = nn.Sequential(
            nn.Linear(d_model, d_ff, bias=False),
            nn.GELU(),
            nn.Dropout(dropout),
            nn.Linear(d_ff, d_model, bias=False),
        )

    def forward(self, x):
        return self.net(x)


# ── Encoder Block — NO positional encoding ──────────────────────────────────

class EncoderBlock(nn.Module):
    """
    Pre-norm encoder block. Purely token-based — no position signal.
    Every token can attend to every other token (bidirectional).
    """

    def __init__(self, d_model: int, n_heads: int, d_ff: int, dropout: float = 0.1):
        super().__init__()
        self.norm1 = nn.LayerNorm(d_model)
        self.attn  = MultiHeadAttention(d_model, n_heads, dropout)
        self.drop1 = nn.Dropout(dropout)

        self.norm2 = nn.LayerNorm(d_model)
        self.ff    = FeedForward(d_model, d_ff, dropout)
        self.drop2 = nn.Dropout(dropout)

    def forward(self, x: torch.Tensor) -> torch.Tensor:
        # Full bidirectional self-attention (no mask)
        x = x + self.drop1(self.attn(self.norm1(x), self.norm1(x)))
        x = x + self.drop2(self.ff(self.norm2(x)))
        return x


class Encoder(nn.Module):
    """
    Token embedding → N encoder blocks.
    No positional encoding added anywhere.
    """

    def __init__(
        self,
        vocab_size: int,
        d_model: int,
        n_heads: int,
        d_ff: int,
        n_layers: int,
        dropout: float = 0.1,
    ):
        super().__init__()
        self.embed  = nn.Embedding(vocab_size, d_model)
        self.drop   = nn.Dropout(dropout)
        self.layers = nn.ModuleList(
            [EncoderBlock(d_model, n_heads, d_ff, dropout) for _ in range(n_layers)]
        )
        self.norm = nn.LayerNorm(d_model)

    def forward(self, src: torch.Tensor) -> torch.Tensor:
        """
        Args:
            src: (batch, src_len)  token ids
        Returns:
            (batch, src_len, d_model)  — no position info encoded
        """
        x = self.drop(self.embed(src))   # raw token embeddings only
        for layer in self.layers:
            x = layer(x)
        return self.norm(x)


# ── Positional Encoding — for decoder only ──────────────────────────────────

class LearnedPositionalEncoding(nn.Module):
    """Learned absolute positional embedding (like GPT-2)."""

    def __init__(self, max_seq_len: int, d_model: int, dropout: float = 0.1):
        super().__init__()
        self.pos_embed = nn.Embedding(max_seq_len, d_model)
        self.dropout   = nn.Dropout(dropout)

    def forward(self, x: torch.Tensor) -> torch.Tensor:
        T = x.size(1)
        positions = torch.arange(T, device=x.device).unsqueeze(0)  # (1, T)
        return self.dropout(x + self.pos_embed(positions))


# ── Decoder Block — WITH positional encoding + cross-attention ───────────────

class DecoderBlock(nn.Module):
    """
    Pre-norm decoder block with three sublayers:
      1. Causal self-attention  (masked, position-aware)
      2. Cross-attention        (queries from decoder, keys/values from encoder)
      3. Feed-forward
    """

    def __init__(self, d_model: int, n_heads: int, d_ff: int, dropout: float = 0.1):
        super().__init__()
        # Sublayer 1: masked self-attention
        self.norm1      = nn.LayerNorm(d_model)
        self.self_attn  = MultiHeadAttention(d_model, n_heads, dropout)
        self.drop1      = nn.Dropout(dropout)

        # Sublayer 2: cross-attention
        self.norm2      = nn.LayerNorm(d_model)
        self.cross_attn = MultiHeadAttention(d_model, n_heads, dropout)
        self.drop2      = nn.Dropout(dropout)

        # Sublayer 3: FFN
        self.norm3      = nn.LayerNorm(d_model)
        self.ff         = FeedForward(d_model, d_ff, dropout)
        self.drop3      = nn.Dropout(dropout)

    def forward(
        self,
        x: torch.Tensor,              # (B, T_tgt, D)  decoder input (with PE)
        enc_out: torch.Tensor,        # (B, T_src, D)  encoder output (no PE)
        causal_mask: torch.Tensor,    # (1, 1, T_tgt, T_tgt)
    ) -> torch.Tensor:
        # 1. Causal self-attention
        x_norm = self.norm1(x)
        x = x + self.drop1(self.self_attn(x_norm, x_norm, causal_mask))

        # 2. Cross-attention: queries from decoder, keys/values from encoder
        x_norm = self.norm2(x)
        x = x + self.drop2(self.cross_attn(x_norm, enc_out, mask=None))

        # 3. Feed-forward
        x = x + self.drop3(self.ff(self.norm3(x)))
        return x


class Decoder(nn.Module):
    """
    Token embedding + positional encoding → N decoder blocks.
    Positional encoding IS added here (unlike the encoder).
    """

    def __init__(
        self,
        vocab_size: int,
        d_model: int,
        n_heads: int,
        d_ff: int,
        n_layers: int,
        max_seq_len: int = 512,
        dropout: float = 0.1,
    ):
        super().__init__()
        self.embed   = nn.Embedding(vocab_size, d_model)
        self.pos_enc = LearnedPositionalEncoding(max_seq_len, d_model, dropout)
        self.layers  = nn.ModuleList(
            [DecoderBlock(d_model, n_heads, d_ff, dropout) for _ in range(n_layers)]
        )
        self.norm = nn.LayerNorm(d_model)

    @staticmethod
    def causal_mask(seq_len: int, device: torch.device) -> torch.Tensor:
        mask = torch.triu(
            torch.ones(seq_len, seq_len, dtype=torch.bool, device=device), diagonal=1
        )
        return mask.unsqueeze(0).unsqueeze(0)   # (1, 1, T, T)

    def forward(
        self,
        tgt: torch.Tensor,      # (batch, tgt_len)  token ids
        enc_out: torch.Tensor,  # (batch, src_len, d_model)
    ) -> torch.Tensor:
        """
        Returns:
            (batch, tgt_len, d_model)
        """
        x    = self.pos_enc(self.embed(tgt))    # token + position embeddings
        mask = self.causal_mask(x.size(1), x.device)

        for layer in self.layers:
            x = layer(x, enc_out, mask)

        return self.norm(x)


# ── Full Seq2Seq Model ────────────────────────────────────────────────────────

class Seq2SeqTransformer(nn.Module):
    """
    Encoder  — no positional encoding  (order-invariant source representation)
    Decoder  — learned positional encoding  (autoregressive, order-sensitive generation)
    """

    def __init__(
        self,
        src_vocab_size: int,
        tgt_vocab_size: int,
        d_model: int       = 256,
        n_heads: int       = 8,
        d_ff: int          = 1024,
        n_enc_layers: int  = 6,
        n_dec_layers: int  = 6,
        max_seq_len: int   = 512,
        dropout: float     = 0.1,
    ):
        super().__init__()
        self.encoder = Encoder(src_vocab_size, d_model, n_heads, d_ff, n_enc_layers, dropout)
        self.decoder = Decoder(tgt_vocab_size, d_model, n_heads, d_ff, n_dec_layers, max_seq_len, dropout)
        self.lm_head = nn.Linear(d_model, tgt_vocab_size, bias=False)

    def forward(
        self,
        src: torch.Tensor,   # (batch, src_len)
        tgt: torch.Tensor,   # (batch, tgt_len)
    ) -> torch.Tensor:
        enc_out = self.encoder(src)               # no PE
        dec_out = self.decoder(tgt, enc_out)      # with PE + cross-attention
        return self.lm_head(dec_out)              # (batch, tgt_len, tgt_vocab_size)


# ── Sanity check ─────────────────────────────────────────────────────────────

if __name__ == "__main__":
    SRC_VOCAB = 8192
    TGT_VOCAB = 8192
    D_MODEL   = 256
    N_HEADS   = 8
    D_FF      = 1024
    N_LAYERS  = 4
    BATCH     = 2
    SRC_LEN   = 48
    TGT_LEN   = 32

    model = Seq2SeqTransformer(
        src_vocab_size=SRC_VOCAB,
        tgt_vocab_size=TGT_VOCAB,
        d_model=D_MODEL,
        n_heads=N_HEADS,
        d_ff=D_FF,
        n_enc_layers=N_LAYERS,
        n_dec_layers=N_LAYERS,
    )

    n_params = sum(p.numel() for p in model.parameters())
    print(f"Total parameters: {n_params:,}")

    src = torch.randint(0, SRC_VOCAB, (BATCH, SRC_LEN))
    tgt = torch.randint(0, TGT_VOCAB, (BATCH, TGT_LEN))

    logits = model(src, tgt)
    print(f"Logits shape: {logits.shape}")   # (2, 32, 8192)

In [2]:
import re
import ast
from collections import Counter
from functools import partial

import torch
from torch.utils.data import Dataset, DataLoader, random_split


# =========================================================
# 1. SPECIAL TOKENS
# =========================================================
PAD_TOKEN  = "<PAD>"
UNK_TOKEN  = "<UNK>"
BOS_TOKEN  = "<BOS>"
EOS_TOKEN  = "<EOS>"
SEP_TOKEN  = "<SEP>"
STEP_TOKEN = "<STEP>"
ING_TOKEN  = "<ING>"

SPECIAL_TOKENS = [
    PAD_TOKEN,
    UNK_TOKEN,
    BOS_TOKEN,
    EOS_TOKEN,
    SEP_TOKEN,
    STEP_TOKEN,
    ING_TOKEN,
]


# =========================================================
# 2. TEXT CLEANING
# =========================================================
def clean_text(text):
    """Lowercase + normalize whitespace."""
    text = str(text).lower().strip()        # str() guard against non-string rows
    text = re.sub(r"\s+", " ", text)
    return text


# =========================================================
# 3. INGREDIENTS -> SOURCE STRING
# =========================================================
def ingredients_to_source(ingredients, sort_ingredients=True):
    """
    ['winter squash', 'honey', 'salt']
    -> '<ING> honey <SEP> salt <SEP> winter squash <EOS>'
    """
    ingredients = [clean_text(x) for x in ingredients]
    if sort_ingredients:
        ingredients = sorted(ingredients)
    source = f" {SEP_TOKEN} ".join(ingredients)
    return f"{ING_TOKEN} {source} {EOS_TOKEN}"


# =========================================================
# 4. STEPS -> TARGET STRING
# =========================================================
def steps_to_target(steps):
    """
    ['remove seeds', 'bake for 20 min']
    -> '<BOS> <STEP> remove seeds <STEP> bake for 20 min <EOS>'
    """
    steps     = [clean_text(s) for s in steps]
    step_text = " ".join(f"{STEP_TOKEN} {s}" for s in steps)
    return f"{BOS_TOKEN} {step_text} {EOS_TOKEN}"


# =========================================================
# 5. SIMPLE TOKENIZER
# =========================================================
def tokenize(text):
    """Whitespace tokenizer — fine since data is already spaced."""
    return text.split()


# =========================================================
# 6. BUILD VOCAB
# =========================================================
def build_vocab(dataset, min_freq=1):
    """
    dataset: list of {'ingredients': [...], 'steps': [...]}
    Returns stoi (word->id) and itos (id->word).
    Special tokens always occupy indices 0-6.
    """
    counter = Counter()
    for sample in dataset:
        counter.update(tokenize(ingredients_to_source(sample["ingredients"])))
        counter.update(tokenize(steps_to_target(sample["steps"])))

    stoi = {}
    itos = []

    # Special tokens first — fixed indices regardless of frequency
    for token in SPECIAL_TOKENS:
        stoi[token] = len(stoi)
        itos.append(token)

    # Regular tokens sorted by frequency (most common = lowest index)
    for token, freq in counter.most_common():
        if token not in stoi and freq >= min_freq:
            stoi[token] = len(stoi)
            itos.append(token)

    return stoi, itos


# =========================================================
# 7. TEXT -> IDS
# =========================================================
def encode(text, stoi):
    """Convert text string to list of token ids."""
    unk_id = stoi[UNK_TOKEN]
    return [stoi.get(tok, unk_id) for tok in tokenize(text)]


# =========================================================
# 8. IDS -> TEXT
# =========================================================
def decode(ids, itos):
    """Convert token ids back to tokens."""
    return [itos[i] for i in ids]


# =========================================================
# 9. DATASET CLASS
# =========================================================
class RecipeDataset(Dataset):
    """
    Each __getitem__ returns:
        src_ids  : LongTensor (src_len,)
        tgt_ids  : LongTensor (tgt_len,)
        src_text : str  (for debugging)
        tgt_text : str  (for debugging)
    """

    def __init__(self, data, stoi, max_src_len=64, max_tgt_len=256):
        self.stoi        = stoi
        self.max_src_len = max_src_len
        self.max_tgt_len = max_tgt_len
        # Drop samples with empty ingredients or steps
        self.data = [
            s for s in data
            if s.get("ingredients") and s.get("steps")
        ]

    def __len__(self):
        return len(self.data)

    def __getitem__(self, idx):
        sample = self.data[idx]

        src_text = ingredients_to_source(sample["ingredients"])
        tgt_text = steps_to_target(sample["steps"])

        src_ids = encode(src_text, self.stoi)[: self.max_src_len]
        tgt_ids = encode(tgt_text, self.stoi)[: self.max_tgt_len]

        return {
            "src_ids":  torch.tensor(src_ids, dtype=torch.long),
            "tgt_ids":  torch.tensor(tgt_ids, dtype=torch.long),
            "src_text": src_text,
            "tgt_text": tgt_text,
        }


# =========================================================
# 10. COLLATE FUNCTION
# =========================================================
def collate_fn(batch, pad_id):
    """
    Pads variable-length sequences to the longest in the batch.

    Returns:
        src_ids               : (B, S)
        tgt_ids               : (B, T)
        src_key_padding_mask  : (B, S)  True = PAD  (plug directly into nn.Transformer)
        tgt_key_padding_mask  : (B, T)  True = PAD
        src_texts             : list[str]
        tgt_texts             : list[str]
    """
    B       = len(batch)
    max_src = max(len(item["src_ids"]) for item in batch)
    max_tgt = max(len(item["tgt_ids"]) for item in batch)

    src_batch = torch.full((B, max_src), pad_id, dtype=torch.long)
    tgt_batch = torch.full((B, max_tgt), pad_id, dtype=torch.long)

    for i, item in enumerate(batch):
        s = len(item["src_ids"])
        t = len(item["tgt_ids"])
        src_batch[i, :s] = item["src_ids"]
        tgt_batch[i, :t] = item["tgt_ids"]

    return {
        "src_ids":              src_batch,
        "tgt_ids":              tgt_batch,
        "src_key_padding_mask": src_batch == pad_id,
        "tgt_key_padding_mask": tgt_batch == pad_id,
        "src_texts":            [item["src_text"] for item in batch],
        "tgt_texts":            [item["tgt_text"] for item in batch],
    }


# =========================================================
# 11. KAGGLE DATA LOADER
# =========================================================
def load_kaggle_data(file_path="RAW_recipes.csv"):
    """
    Downloads RAW_recipes.csv from Kaggle via kagglehub and returns
    a list of {'ingredients': [...], 'steps': [...]} dicts.
    Uses ast.literal_eval (safe) instead of eval().
    """
    import kagglehub
    from kagglehub import KaggleDatasetAdapter

    print(f"Downloading {file_path} from Kaggle...")
    # dataset_load() is the current API — load_dataset() is deprecated
    df = kagglehub.dataset_load(
        KaggleDatasetAdapter.PANDAS,
        "shuyangli94/food-com-recipes-and-user-interactions",
        file_path,
    )
    print(f"Downloaded {len(df)} rows. Parsing...")

    data_list = []
    for _, row in df.iterrows():
        try:
            ingredients = ast.literal_eval(row["ingredients"])  # safe parse
            steps       = ast.literal_eval(row["steps"])        # safe parse
            if isinstance(ingredients, list) and isinstance(steps, list):
                data_list.append({"ingredients": ingredients, "steps": steps})
        except (ValueError, SyntaxError):
            continue    # skip malformed rows

    print(f"Valid samples after parsing: {len(data_list)}")
    return data_list


# =========================================================
# 12. GET DATALOADERS  (single entry point)
# =========================================================
def get_dataloaders(
    file_path    = "RAW_recipes.csv",
    min_freq     = 2,
    max_src_len  = 64,
    max_tgt_len  = 256,
    batch_size   = 32,
    val_split    = 0.1,
    test_split   = 0.1,
    num_workers  = 0,
    seed         = 42,
    pin_memory   = False,      # ← set True only when CUDA is available
):
    """
    Full pipeline:
        Kaggle download → parse → build vocab → Dataset
        → reproducible train/val/test split → DataLoaders

    Returns:
        train_loader, val_loader, test_loader, stoi, itos
    """
    # 1. Load
    data_list = load_kaggle_data(file_path)

    if not data_list:
        raise RuntimeError("No valid samples loaded. Check the Kaggle dataset columns.")

    # 2. Vocab built on FULL data before splitting
    #    (ensures val/test tokens are not all <UNK>)
    print("Building vocabulary...")
    stoi, itos = build_vocab(data_list, min_freq=min_freq)
    print(f"Vocabulary size: {len(stoi)}")

    # 3. Full dataset (empty-sample filter happens inside __init__)
    full_ds = RecipeDataset(data_list, stoi, max_src_len, max_tgt_len)
    N = len(full_ds)
    print(f"Total valid samples: {N}")

    # 4. Reproducible split
    n_test  = int(N * test_split)
    n_val   = int(N * val_split)
    n_train = N - n_val - n_test

    train_ds, val_ds, test_ds = random_split(
        full_ds,
        [n_train, n_val, n_test],
        generator=torch.Generator().manual_seed(seed),
    )
    print(f"Train: {len(train_ds)} | Val: {len(val_ds)} | Test: {len(test_ds)}")

    # 5. Collate with pad_id baked in
    collate = partial(collate_fn, pad_id=stoi[PAD_TOKEN])

    train_loader = DataLoader(
        train_ds, batch_size=batch_size, shuffle=True,
        collate_fn=collate, num_workers=num_workers, pin_memory=pin_memory,
    )
    val_loader = DataLoader(
        val_ds, batch_size=batch_size, shuffle=False,
        collate_fn=collate, num_workers=num_workers, pin_memory=pin_memory,
    )
    test_loader = DataLoader(
        test_ds, batch_size=batch_size, shuffle=False,
        collate_fn=collate, num_workers=num_workers, pin_memory=pin_memory,
    )

    return train_loader, val_loader, test_loader, stoi, itos


# =========================================================
# 13. MAIN
# =========================================================
# if __name__ == "__main__":

#     train_loader, val_loader, test_loader, stoi, itos = get_dataloaders(
#         file_path   = "RAW_recipes.csv",
#         min_freq    = 2,
#         max_src_len = 64,
#         max_tgt_len = 256,
#         batch_size  = 32,
#         val_split   = 0.1,
#         test_split  = 0.1,
#         num_workers = 0,
#     )

#     print("\nSpecial token ids:")
#     for tok in SPECIAL_TOKENS:
#         print(f"  {tok:12s} → {stoi[tok]}")

#     # Inspect one training batch
#     batch = next(iter(train_loader))

    # print(f"\nSrc batch shape            : {batch['src_ids'].shape}")
    # print(f"Tgt batch shape            : {batch['tgt_ids'].shape}")
    # print(f"Src key padding mask shape : {batch['src_key_padding_mask'].shape}")
    # print(f"Tgt key padding mask shape : {batch['tgt_key_padding_mask'].shape}")

    # print("\nSample source text :", batch["src_texts"][0])
    # print("Sample target text :", batch["tgt_texts"][0])
    # print("Decoded src        :", decode(batch["src_ids"][0].tolist(), itos))
    # print("Decoded tgt        :", decode(batch["tgt_ids"][0].tolist(), itos)[:20], "...")

In [3]:
import math
import time
import os
import torch
import torch.nn as nn
import torch.nn.functional as F
from torch.optim import AdamW
from torch.optim.lr_scheduler import CosineAnnealingLR
from tqdm import tqdm

# from recipe_dataset_v2 import (
#     get_dataloaders,
#     decode,
#     PAD_TOKEN, BOS_TOKEN, EOS_TOKEN, SPECIAL_TOKENS,
# )
# from transformer_hybrid_pe import Seq2SeqTransformer

os.environ["PYTORCH_ALLOC_CONF"] = "expandable_segments:True"


# =========================================================
# CONFIG
# =========================================================
N_GPUS = torch.cuda.device_count()   # 2 for T4×2

CFG = dict(
    # Data
    file_path    = "RAW_recipes.csv",
    min_freq     = 5,          # ← was 2, cuts vocab 32K → ~8K
    max_src_len  = 40,
    max_tgt_len  = 256,
    batch_size   = 64,          # per GPU → 128 total
    grad_accum   = 1,
    val_split    = 0.1,
    test_split   = 0.1,
    num_workers  = 4,
    seed         = 42,

    # Model
    d_model      = 512,         # ← was 256, cuts params by 4×
    n_heads      = 8,           # ← was 8  (d_k stays 32)
    d_ff         = 2048,         # ← was 1024
    n_enc_layers = 4,           # ← was 4
    n_dec_layers = 5,           # ← was 4
    dropout      = 0.1,

    # Training
    epochs       = 40,
    lr           = 1e-4,
    clip_grad    = 1.0,
    save_path    = "/kaggle/working/best_model_d_mod-512,decl5,epch-40.pt",
    checkpoint_dir = "/kaggle/working/checkpoints/",   
)

# =========================================================
# DEVICE  — primary GPU is always cuda:0
# =========================================================
def get_device() -> torch.device:
    if torch.cuda.is_available():
        return torch.device("cuda")       # cuda = cuda:0 (primary)
    elif torch.backends.mps.is_available():
        return torch.device("mps")
    return torch.device("cpu")


def print_gpu_memory(tag=""):
    """Print memory for every available GPU."""
    for i in range(torch.cuda.device_count()):
        alloc  = torch.cuda.memory_allocated(i)  / 1024**3
        reserv = torch.cuda.memory_reserved(i)   / 1024**3
        total  = torch.cuda.get_device_properties(i).total_memory / 1024**3
        tqdm.write(
            f"[GPU{i} {tag}] alloc={alloc:.2f}GB  "
            f"reserved={reserv:.2f}GB  total={total:.2f}GB"
        )


# =========================================================
# STEP 1 — Dataloaders
# =========================================================
def build_data(cfg, device):
    pin = (device.type == "cuda")
    return get_dataloaders(
        file_path   = cfg["file_path"],
        min_freq    = cfg["min_freq"],
        max_src_len = cfg["max_src_len"],
        max_tgt_len = cfg["max_tgt_len"],
        batch_size  = cfg["batch_size"] * N_GPUS,  # DataParallel splits this across GPUs
        val_split   = cfg["val_split"],
        test_split  = cfg["test_split"],
        num_workers = cfg["num_workers"],
        seed        = cfg["seed"],
        pin_memory  = pin,
    )


# =========================================================
# STEP 2 — Model + DataParallel wrapping
# =========================================================
def build_model(cfg, vocab_size, pad_idx, device):
    """
    DataParallel (DP) — simplest multi-GPU setup.

    How it works:
      1. Each forward pass, DP splits the batch across all GPUs along dim 0.
         e.g. batch=32 → GPU0 gets [0:16], GPU1 gets [16:32]
      2. Each GPU runs a full forward pass in parallel.
      3. DP collects outputs back to GPU0, computes loss, scatters gradients.
      4. One optimizer.step() updates weights on GPU0; DP re-syncs all GPUs.

    Limitation: GPU0 does more work (loss reduction + gradient sync).
    For better balance, use DistributedDataParallel (see bottom of file).
    But DP requires zero code changes to the model and works great for 2 GPUs.
    """
    model = Seq2SeqTransformer(
        src_vocab_size = vocab_size,
        tgt_vocab_size = vocab_size,
        d_model        = cfg["d_model"],
        n_heads        = cfg["n_heads"],
        d_ff           = cfg["d_ff"],
        n_enc_layers   = cfg["n_enc_layers"],
        n_dec_layers   = cfg["n_dec_layers"],
        dropout        = cfg["dropout"],
    )
    model.encoder.embed.padding_idx = pad_idx
    model.decoder.embed.padding_idx = pad_idx

    model = model.to(device)

    if N_GPUS > 1:
        print(f"Wrapping model with DataParallel across {N_GPUS} GPUs: "
              f"{[torch.cuda.get_device_name(i) for i in range(N_GPUS)]}")
        model = nn.DataParallel(model)   # wraps model, splits batches automatically

    return model


def unwrap(model):
    """
    DataParallel wraps the model in model.module.
    Use this to access the real model (e.g. for encoder/decoder in inference).
    """
    return model.module if isinstance(model, nn.DataParallel) else model


# =========================================================
# STEP 3 — Loss
# =========================================================
def build_criterion(pad_idx):
    return nn.CrossEntropyLoss(ignore_index=pad_idx, label_smoothing=0.1)


# =========================================================
# STEP 4 — Helpers
# =========================================================
def make_tgt_input_and_label(tgt_ids):
    return tgt_ids[:, :-1], tgt_ids[:, 1:]


def train_one_epoch(model, loader, optimizer, criterion, device, cfg, epoch, total_epochs, scaler):
    model.train()
    total_loss = 0.0
    grad_accum = cfg["grad_accum"]
    accum_loss = 0.0
    use_amp    = (device.type == "cuda")

    optimizer.zero_grad()

    pbar = tqdm(
        loader,
        desc          = f"Epoch {epoch:03d}/{total_epochs} [train]",
        unit          = "batch",
        leave         = False,
        dynamic_ncols = True,
    )

    for step, batch in enumerate(pbar, 1):
        src = batch["src_ids"].to(device)
        tgt = batch["tgt_ids"].to(device)

        tgt_in, tgt_lbl = make_tgt_input_and_label(tgt)

        # fp16 autocast: halves memory, doubles throughput on T4
        with torch.autocast(device_type=device.type, enabled=use_amp):
            logits = model(src, tgt_in)            # (B, T-1, vocab)
            loss   = criterion(
                logits.reshape(-1, logits.size(-1)),
                tgt_lbl.reshape(-1),
            ) / grad_accum

        # GradScaler prevents fp16 underflow during backward
        scaler.scale(loss).backward()
        accum_loss += loss.item()

        if step % grad_accum == 0 or step == len(loader):
            scaler.unscale_(optimizer)
            nn.utils.clip_grad_norm_(model.parameters(), cfg["clip_grad"])
            scaler.step(optimizer)
            scaler.update()
            optimizer.zero_grad()

            total_loss += accum_loss
            n_updates   = (step - 1) // grad_accum + 1
            pbar.set_postfix({
                "avg":   f"{total_loss / n_updates:.4f}",
                "batch": f"{accum_loss * grad_accum:.4f}",
                "scale": f"{scaler.get_scale():.0f}",
            })
            accum_loss = 0.0

    pbar.close()
    return total_loss / math.ceil(len(loader) / grad_accum)


@torch.no_grad()
def evaluate(model, loader, criterion, device, epoch, total_epochs):
    model.eval()
    total_loss = 0.0

    pbar = tqdm(
        loader,
        desc          = f"Epoch {epoch:03d}/{total_epochs} [val]  ",
        unit          = "batch",
        leave         = False,
        dynamic_ncols = True,
    )

    for step, batch in enumerate(pbar, 1):
        src = batch["src_ids"].to(device)
        tgt = batch["tgt_ids"].to(device)

        tgt_in, tgt_lbl = make_tgt_input_and_label(tgt)

        with torch.autocast(device_type="cuda", enabled=(device.type == "cuda")):
            logits = model(src, tgt_in)
            loss   = criterion(
                logits.reshape(-1, logits.size(-1)),
                tgt_lbl.reshape(-1),
            )

        total_loss += loss.item()
        pbar.set_postfix({"avg": f"{total_loss / step:.4f}"})

    pbar.close()
    return total_loss / len(loader)


# =========================================================
# STEP 5 — Greedy decode
# NOTE: unwrap() to access encoder/decoder directly on GPU0
# =========================================================
@torch.no_grad()
def greedy_decode(model, src_ids, stoi, itos, max_tgt_len, device):
    core    = unwrap(model)          # get real model from under DataParallel
    core.eval()

    bos_id  = stoi[BOS_TOKEN]
    eos_id  = stoi[EOS_TOKEN]
    src     = torch.tensor(src_ids, dtype=torch.long).unsqueeze(0).to(device)
    enc_out = core.encoder(src)      # single sample — no need for DataParallel
    tgt_ids = [bos_id]

    for _ in range(max_tgt_len):
        tgt     = torch.tensor(tgt_ids, dtype=torch.long).unsqueeze(0).to(device)
        dec_out = core.decoder(tgt, enc_out)
        logits  = core.lm_head(dec_out)
        next_id = logits[0, -1, :].argmax(dim=-1).item()
        tgt_ids.append(next_id)
        if next_id == eos_id:
            break

    return " ".join(decode(tgt_ids, itos))


# =========================================================
# STEP 6 — Training loop
# =========================================================
def train(cfg, resume_from: str = None):
    """
    resume_from : path to a checkpoint .pt file to resume training from.
                  If None, trains from scratch.
    """
    device = get_device()
 
    print(f"Using device  : {device}")
    print(f"GPUs available: {N_GPUS}")
    for i in range(N_GPUS):
        total = torch.cuda.get_device_properties(i).total_memory / 1024**3
        print(f"  GPU{i}: {torch.cuda.get_device_name(i)}  ({total:.1f} GB)")
 
    train_loader, val_loader, test_loader, stoi, itos = build_data(cfg, device)
 
    vocab_size = len(stoi)
    pad_idx    = stoi[PAD_TOKEN]
    eff_batch  = cfg["batch_size"] * N_GPUS * cfg["grad_accum"]
    print(f"\nVocab size    : {vocab_size}  |  PAD idx: {pad_idx}")
    print(f"Per-GPU batch : {cfg['batch_size']}")
    print(f"Total batch   : {cfg['batch_size'] * N_GPUS}  (split across {N_GPUS} GPUs)")
    print(f"Grad accum    : {cfg['grad_accum']}  →  effective batch: {eff_batch}")
 
    model    = build_model(cfg, vocab_size, pad_idx, device)
    n_params = sum(p.numel() for p in unwrap(model).parameters() if p.requires_grad)
    print(f"Trainable params: {n_params:,}\n")
 
    print_gpu_memory("after model load")
 
    optimizer = AdamW(model.parameters(), lr=cfg["lr"], weight_decay=1e-2)
    scheduler = CosineAnnealingLR(optimizer, T_max=cfg["epochs"])
    criterion = build_criterion(pad_idx)
    scaler    = torch.cuda.amp.GradScaler(enabled=(device.type == "cuda"))
 
    best_val_loss = float("inf")
    start_epoch   = 1
    history       = []
 
    # ── Resume from checkpoint if provided ────────────────
    if resume_from is not None:
        import os
        if not os.path.exists(resume_from):
            print(f"WARNING: checkpoint not found at {resume_from}. Starting from scratch.")
        else:
            print(f"Resuming from checkpoint: {resume_from}")
            ckpt = torch.load(resume_from, map_location=device)
 
            unwrap(model).load_state_dict(ckpt["model"])
            optimizer.load_state_dict(ckpt["optimizer"])
 
            # Fast-forward the scheduler to match saved epoch
            # so LR continues from where it left off
            saved_epoch = ckpt["epoch"]
            for _ in range(saved_epoch):
                scheduler.step()
 
            best_val_loss = ckpt["val_loss"]
            start_epoch   = saved_epoch + 1    # resume from NEXT epoch
 
            print(f"  Resumed from epoch {saved_epoch} | "
                  f"best val loss so far: {best_val_loss:.4f} | "
                  f"continuing from epoch {start_epoch}")
 
    if start_epoch > cfg["epochs"]:
        print(f"Already trained for {cfg['epochs']} epochs. Nothing to do.")
        return unwrap(model), stoi, itos, history
 
    epoch_bar = tqdm(
        range(start_epoch, cfg["epochs"] + 1),
        desc          = "Training",
        unit          = "epoch",
        dynamic_ncols = True,
        position      = 0,
    )
 
    for epoch in epoch_bar:
        t0 = time.time()
 
        train_loss = train_one_epoch(
            model, train_loader, optimizer, criterion,
            device, cfg, epoch, cfg["epochs"], scaler,
        )
        val_loss = evaluate(
            model, val_loader, criterion,
            device, epoch, cfg["epochs"],
        )
        scheduler.step()
        elapsed = time.time() - t0
 
        saved = ""
        if val_loss < best_val_loss:
            best_val_loss = val_loss
            torch.save({
                "epoch":     epoch,
                # Save unwrapped model — not the DataParallel wrapper
                "model":     unwrap(model).state_dict(),
                "optimizer": optimizer.state_dict(),
                "val_loss":  val_loss,
                "stoi":      stoi,
                "itos":      itos,
                "cfg":       cfg,
            }, cfg["save_path"])
            saved = "  ✓ saved"
 
        tqdm.write(
            f"Epoch {epoch:03d}/{cfg['epochs']} | "
            f"train {train_loss:.4f} | "
            f"val {val_loss:.4f} | "
            f"lr {scheduler.get_last_lr()[0]:.1e} | "
            f"{elapsed:.0f}s{saved}"
        )
        print_gpu_memory(f"epoch {epoch}")
 
        history.append({"epoch": epoch, "train_loss": train_loss, "val_loss": val_loss})
        epoch_bar.set_postfix({
            "train": f"{train_loss:.4f}",
            "val":   f"{val_loss:.4f}",
            "best":  f"{best_val_loss:.4f}",
        })

    epoch_bar.close()
    print("\nTraining complete.")

    # Reload best checkpoint — load into unwrapped model
    checkpoint = torch.load(cfg["save_path"], map_location=device)
    unwrap(model).load_state_dict(checkpoint["model"])
    test_loss = evaluate(model, test_loader, criterion, device, epoch, cfg["epochs"])
    print(f"Test loss (best checkpoint): {test_loss:.4f}")

    return model, stoi, itos, history


# =========================================================
# STEP 7 — Demo inference
# =========================================================
def demo_inference(model, stoi, itos, device, max_tgt_len=128):

    sample_ingredients = [
        "winter squash", "mexican seasoning", "mixed spice",
        "honey", "butter", "olive oil", "salt"
    ]
    src_text = ingredients_to_source(sample_ingredients)
    src_ids  = encode(src_text, stoi)

    print("\nIngredients :", sample_ingredients)
    generated = greedy_decode(model, src_ids, stoi, itos, max_tgt_len, device)
    print("Generated   :", generated)


# =========================================================
# MAIN
# =========================================================
# if __name__ == "__main__":
#     model, stoi, itos, history = train(CFG)
#     demo_inference(model, stoi, itos, get_device())

In [ ]:
model, stoi, itos, history = train(CFG, resume_from="/kaggle/working/best_model_d_mod-512,decl5,epch-40.pt")

Using device  : cuda
GPUs available: 2
  GPU0: Tesla T4  (14.6 GB)
  GPU1: Tesla T4  (14.6 GB)
Downloaded 231637 rows. Parsing...
Valid samples after parsing: 231637
Building vocabulary...
Vocabulary size: 17230
Total valid samples: 231636
Train: 185310 | Val: 23163 | Test: 23163

Vocab size    : 17230  |  PAD idx: 0
Per-GPU batch : 64
Total batch   : 128  (split across 2 GPUs)
Grad accum    : 1  →  effective batch: 128
Wrapping model with DataParallel across 2 GPUs: ['Tesla T4', 'Tesla T4']
Trainable params: 60,307,456

[GPU0 after model load] alloc=0.22GB  reserved=0.23GB  total=14.56GB
[GPU1 after model load] alloc=0.00GB  reserved=0.00GB  total=14.56GB


/tmp/ipykernel_55/1109583226.py:310: FutureWarning: `torch.cuda.amp.GradScaler(args...)` is deprecated. Please use `torch.amp.GradScaler('cuda', args...)` instead.
  scaler    = torch.cuda.amp.GradScaler(enabled=(device.type == "cuda"))


Epoch 001/40 [train]: 100%|██████████| 1448/1448 [15:15<00:00,  1.70batch/s, avg=4.6367, batch=4.0293, scale=65536]
                                                                                                                   
Training:   2%|▎         | 1/40 [16:01<10:24:39, 961.01s/epoch, train=4.6367, val=3.9591, best=3.9591]

Epoch 001/40 | train 4.6367 | val 3.9591 | lr 1.0e-04 | 960s  ✓ saved
[GPU0 epoch 1] alloc=0.69GB  reserved=13.12GB  total=14.56GB
[GPU1 epoch 1] alloc=0.02GB  reserved=4.89GB  total=14.56GB



Epoch 002/40 [train]: 100%|██████████| 1448/1448 [15:22<00:00,  1.70batch/s, avg=3.8827, batch=3.9066, scale=131072]
                                                                                                                    
Training:   5%|▌         | 2/40 [32:09<10:11:28, 965.49s/epoch, train=3.8827, val=3.6958, best=3.6958]

...


Epoch 029/40 [train]: 100%|██████████| 1448/1448 [15:24<00:00,  1.69batch/s, avg=3.0590, batch=3.0996, scale=4194304]
                                                                                                                     
Training:  72%|███████▎  | 29/40 [7:48:27<2:57:51, 970.15s/epoch, train=3.0590, val=3.1742, best=3.1742]

Epoch 029/40 | train 3.0590 | val 3.1742 | lr 1.8e-05 | 969s  ✓ saved
[GPU0 epoch 29] alloc=0.69GB  reserved=13.16GB  total=14.56GB
[GPU1 epoch 29] alloc=0.02GB  reserved=4.89GB  total=14.56GB



Epoch 030/40 [train]: 100%|██████████| 1448/1448 [15:22<00:00,  1.70batch/s, avg=3.0544, batch=3.0924, scale=2097152]
                                                                                                                     
Training:  75%|███████▌  | 30/40 [8:04:37<2:41:40, 970.04s/epoch, train=3.0544, val=3.1736, best=3.1736]

Epoch 030/40 | train 3.0544 | val 3.1736 | lr 1.5e-05 | 968s  ✓ saved
[GPU0 epoch 30] alloc=0.69GB  reserved=13.16GB  total=14.56GB
[GPU1 epoch 30] alloc=0.02GB  reserved=4.89GB  total=14.56GB



Epoch 031/40 [train]:  77%|███████▋  | 1114/1448 [11:50<03:32,  1.57batch/s, avg=3.0496, batch=3.0315, scale=2097152]

In [ ]:
import torch
import torch.nn as nn
from collections import Counter

# from recipe_dataset_v2 import (
#     ingredients_to_source,
#     encode,
#     decode,
#     PAD_TOKEN, BOS_TOKEN, EOS_TOKEN, STEP_TOKEN,
# )
# from transformer_hybrid_pe import Seq2SeqTransformer


# =========================================================
# 1. LOAD CHECKPOINT
# =========================================================
def load_model(checkpoint_path: str, device: torch.device):
    print(f"Loading checkpoint from: {checkpoint_path}")
    checkpoint = torch.load(checkpoint_path, map_location=device)

    cfg  = checkpoint["cfg"]
    stoi = checkpoint["stoi"]
    itos = checkpoint["itos"]

    print(f"  Saved at epoch : {checkpoint['epoch']}")
    print(f"  Val loss       : {checkpoint['val_loss']:.4f}")
    print(f"  Vocab size     : {len(stoi)}")

    model = Seq2SeqTransformer(
        src_vocab_size = len(stoi),
        tgt_vocab_size = len(stoi),
        d_model        = cfg["d_model"],
        n_heads        = cfg["n_heads"],
        d_ff           = cfg["d_ff"],
        n_enc_layers   = cfg["n_enc_layers"],
        n_dec_layers   = cfg["n_dec_layers"],
        dropout        = cfg["dropout"],
    )
    model.load_state_dict(checkpoint["model"])
    model.to(device)
    model.eval()
    print("  Model loaded and ready.\n")
    return model, stoi, itos, cfg


# =========================================================
# 2. REPETITION PENALTY HELPER
# =========================================================
def apply_repetition_penalty(logits, generated_ids, penalty=1.3):
    """
    Divides the logit of any token that has already been generated
    by `penalty`. Values > 1.0 discourage repeats.

    penalty=1.0  → no effect
    penalty=1.3  → mild suppression (recommended)
    penalty=1.5  → strong suppression
    penalty=2.0  → nearly bans any repeated token
    """
    for token_id in set(generated_ids):
        if logits[token_id] > 0:
            logits[token_id] /= penalty
        else:
            logits[token_id] *= penalty
    return logits


def apply_ngram_block(logits, generated_ids, ngram_size=3):
    """
    Blocks any token that would continue a repeated n-gram.
    e.g. if "add the flour" already appeared, blocks "flour"
    after seeing "add the" again.

    ngram_size=3 blocks repeated trigrams — good default.
    """
    if len(generated_ids) < ngram_size:
        return logits

    # Get the last (ngram_size - 1) tokens as the current context window
    window = tuple(generated_ids[-(ngram_size - 1):])

    # Find all ngrams in history and record what followed each window
    blocked = set()
    for i in range(len(generated_ids) - ngram_size + 1):
        past_window = tuple(generated_ids[i: i + ngram_size - 1])
        if past_window == window:
            next_token = generated_ids[i + ngram_size - 1]
            blocked.add(next_token)

    for token_id in blocked:
        logits[token_id] = float("-inf")

    return logits


# =========================================================
# 3. GREEDY DECODE  (with repetition penalty + ngram block)
# =========================================================
@torch.no_grad()
def greedy_decode(
    model, src_ids, stoi, itos, max_tgt_len, device,
    repetition_penalty = 1.3,
    ngram_block        = 3,
):
    bos_id = stoi[BOS_TOKEN]
    eos_id = stoi[EOS_TOKEN]

    src     = torch.tensor(src_ids, dtype=torch.long).unsqueeze(0).to(device)
    enc_out = model.encoder(src)
    tgt_ids = [bos_id]

    for _ in range(max_tgt_len):
        tgt     = torch.tensor(tgt_ids, dtype=torch.long).unsqueeze(0).to(device)
        dec_out = model.decoder(tgt, enc_out)
        logits  = model.lm_head(dec_out)[0, -1, :].clone()   # (vocab_size,)

        # Apply repetition penalty
        if repetition_penalty != 1.0:
            logits = apply_repetition_penalty(logits, tgt_ids, repetition_penalty)

        # Block repeated n-grams
        if ngram_block > 0:
            logits = apply_ngram_block(logits, tgt_ids, ngram_block)

        next_id = logits.argmax(dim=-1).item()
        tgt_ids.append(next_id)
        if next_id == eos_id:
            break

    return tgt_ids


# =========================================================
# 4. SAMPLING DECODE  (with repetition penalty + ngram block)
# =========================================================
@torch.no_grad()
def sample_decode(
    model, src_ids, stoi, itos, max_tgt_len, device,
    temperature        = 1.0,           # safer default for undertrained models
    top_k              = 50,
    top_p              = 0.95,          # less aggressive than 0.9
    repetition_penalty = 1.3,
    ngram_block        = 3,
):
    bos_id = stoi[BOS_TOKEN]
    eos_id = stoi[EOS_TOKEN]

    src     = torch.tensor(src_ids, dtype=torch.long).unsqueeze(0).to(device)
    enc_out = model.encoder(src)
    tgt_ids = [bos_id]

    for _ in range(max_tgt_len):
        tgt     = torch.tensor(tgt_ids, dtype=torch.long).unsqueeze(0).to(device)
        dec_out = model.decoder(tgt, enc_out)
        logits  = model.lm_head(dec_out)[0, -1, :].clone()   # (vocab_size,)

        # Repetition penalty
        if repetition_penalty != 1.0:
            logits = apply_repetition_penalty(logits, tgt_ids, repetition_penalty)

        # N-gram blocking
        if ngram_block > 0:
            logits = apply_ngram_block(logits, tgt_ids, ngram_block)

        # Temperature
        logits = logits / temperature

        # Top-k
        if top_k > 0:
            top_k_vals = torch.topk(logits, min(top_k, logits.size(-1))).values
            logits[logits < top_k_vals[-1]] = float("-inf")

        # Top-p (nucleus)
        if top_p < 1.0:
            sorted_logits, sorted_idx = torch.sort(logits, descending=True)
            cumulative_probs = torch.cumsum(
                torch.softmax(sorted_logits, dim=-1), dim=-1
            )
            # Keep at least 1 token — shift mask by 1 so the first token is always kept
            remove_mask = cumulative_probs > top_p
            remove_mask[..., 1:] = remove_mask[..., :-1].clone()
            remove_mask[..., 0]  = False
            sorted_logits[remove_mask] = float("-inf")
            logits = sorted_logits.scatter(0, sorted_idx, sorted_logits)

        # Safety: if everything is -inf (all tokens blocked by ngram/penalty),
        # fall back to the raw logits from before filtering so we never get nan
        if torch.all(logits == float("-inf")):
            tgt     = torch.tensor(tgt_ids, dtype=torch.long).unsqueeze(0).to(device)
            dec_out = model.decoder(tgt, enc_out)
            logits  = model.lm_head(dec_out)[0, -1, :].clone()

        probs = torch.softmax(logits, dim=-1)

        # Final nan/inf guard — if probs still broken, fall back to uniform
        if torch.isnan(probs).any() or torch.isinf(probs).any() or probs.sum() <= 0:
            probs = torch.ones_like(probs) / probs.size(-1)

        next_id = torch.multinomial(probs, num_samples=1).item()
        tgt_ids.append(next_id)
        if next_id == eos_id:
            break

    return tgt_ids


# =========================================================
# 5. FORMAT OUTPUT — ids → readable step list
# =========================================================
def format_recipe(token_ids: list, itos: list) -> list:
    """
    [BOS, STEP, remove, seeds, STEP, bake, at, 350, EOS]
    → ['remove seeds', 'bake at 350']
    """
    tokens  = decode(token_ids, itos)
    tokens  = [t for t in tokens if t not in (BOS_TOKEN, EOS_TOKEN)]

    steps, current = [], []
    for tok in tokens:
        if tok == STEP_TOKEN:
            if current:
                steps.append(" ".join(current).strip())
            current = []
        else:
            current.append(tok)
    if current:
        steps.append(" ".join(current).strip())

    return [s for s in steps if s]


# =========================================================
# 6. MAIN GENERATE FUNCTION
# =========================================================
def generate_recipe(
    ingredients: list,
    model,
    stoi: dict,
    itos: list,
    device,
    max_tgt_len        = 256,
    mode               = "greedy",      # "greedy" or "sample"
    temperature        = 1.0,           # higher = safer for undertrained models
    top_k              = 50,
    top_p              = 0.95,          # raised from 0.9 — less aggressive filtering
    repetition_penalty = 1.3,           # 1.0 = off, 1.3 = mild, 1.5 = strong
    ngram_block        = 3,             # 0 = off, 3 = block repeated trigrams
) -> list:
    src_text = ingredients_to_source(ingredients)
    src_ids  = encode(src_text, stoi)

    if mode == "greedy":
        token_ids = greedy_decode(
            model, src_ids, stoi, itos, max_tgt_len, device,
            repetition_penalty=repetition_penalty,
            ngram_block=ngram_block,
        )
    else:
        token_ids = sample_decode(
            model, src_ids, stoi, itos, max_tgt_len, device,
            temperature=temperature, top_k=top_k, top_p=top_p,
            repetition_penalty=repetition_penalty,
            ngram_block=ngram_block,
        )

    return format_recipe(token_ids, itos)


# =========================================================
# 7. PRETTY PRINT
# =========================================================
def print_recipe(ingredients: list, steps: list, title: str = ""):
    if title:
        print(f"\n{'─'*50}")
        print(title)
    print(f"\n{'─'*50}")
    print("INGREDIENTS:")
    for ing in ingredients:
        print(f"  • {ing}")
    print("\nGENERATED STEPS:")
    if not steps:
        print("  (no steps generated — model needs more training)")
    for i, step in enumerate(steps, 1):
        print(f"  {i}. {step}")
    print(f"{'─'*50}\n")


# =========================================================
# 8. RUN
# =========================================================
if __name__ == "__main__":
    CHECKPOINT = "/kaggle/working/best_model_d_mod-256,epch-20.pt"
    MAX_LEN    = 256
    device     = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    print(f"Device: {device}")

    model, stoi, itos, cfg = load_model(CHECKPOINT, device)

    ingredients_1 = [
        "winter squash", "mexican seasoning", "mixed spice",
        "honey", "butter", "olive oil", "salt"
    ]

    # Greedy — deterministic, repetition penalty ON
    steps = generate_recipe(
        ingredients_1, model, stoi, itos, device,
        max_tgt_len=MAX_LEN, mode="greedy",
        repetition_penalty=1.3, ngram_block=3,
    )
    print_recipe(ingredients_1, steps, "Greedy (rep penalty=1.3, ngram block=3)")

    # Sampling — more varied output
    steps = generate_recipe(
        ingredients_1, model, stoi, itos, device,
        max_tgt_len=MAX_LEN, mode="sample",
        temperature=1.0, top_k=50, top_p=0.95,
        repetition_penalty=1.3, ngram_block=3,
    )
    print_recipe(ingredients_1, steps, "Sampled (temp=1.0, top_k=50, top_p=0.95)")

    # Interactive
    print("\nEnter ingredients (comma-separated) or 'quit':")
    while True:
        user_input = input("> ").strip()
        if user_input.lower() in ("quit", "q", "exit"):
            break
        if not user_input:
            continue
        ings  = [i.strip() for i in user_input.split(",")]
        steps = generate_recipe(
            ings, model, stoi, itos, device,
            mode="sample", repetition_penalty=1.3, ngram_block=3,
        )
        print_recipe(ings, steps)

In [ ]:
from IPython.display import FileLink
FileLink('/kaggle/working/best_model_d_mod-128,epch-17.pt')